# Model D: Stage 2 tuning (grid search on VALIDATION)

The paper allows a grid search for the Focal Loss parameters. Every candidate starts from the same Stage 1
weights (D2), trains Stage 2 with seed 42, and is scored on the **validation** set only. The winner is then trained
with seeds 43 and 44, and only then is the **test** set used (once) for the SOP tables.

| Candidate | Focal γ | Frozen layers | Status |
|---|---|---|---|
| g2.0_f11 (current full D) | 2.0 | 0–10 (whole backbone) | done |
| g1.0_f11 | 1.0 | 0–10 | this notebook |
| g1.5_f11 | 1.5 | 0–10 | this notebook |
| g2.5_f11 | 2.5 | 0–10 | this notebook |
| g2.0_f9 | 2.0 | 0–8 (SPPF + C2PSA trainable) | this notebook |

**Selection rule (fixed before training):** highest mean of validation mAP@50 and mAP@50-95 (the two SOP 1 metrics)
at each run's best epoch. α = 0.25, lr0 = 0.0002, 150 epochs, patience 50, batch 8, 640 for every candidate.

About 20–25 min per run: ~1.5 h for the 4 candidates, ~45 min for the winner's seeds 43 and 44.
If it stops, Run All again: finished runs are skipped and an interrupted one resumes.


## Setup

In [1]:
import os, sys, json, shutil, csv
from pathlib import Path
os.environ.setdefault('MPLBACKEND', 'Agg')

HERE = Path.cwd().resolve()
if not (HERE / 'sop_analysis.py').is_file():
    HERE = HERE / 'final'
assert (HERE / 'sop_analysis.py').is_file(), 'Open this notebook from ablation_training/final.'
ROOT = HERE.parent
DATA_YAML = ROOT / 'datasets' / 'ablation_yolov26' / 'ModelD2_lesion_ita' / 'data.yaml'
WEIGHTS_ROOT = ROOT / 'weights' / 'ablation_split'
RUNS = ROOT / 'runs' / 'ablation_split' / 'training'
CHOICE_FILE = HERE / 'd_tuning_choice.json'

FOCAL_ALPHA = 0.25
EPOCHS, PATIENCE, LR0, BATCH, IMG_SIZE = 150, 50, 0.0002, 8, 640
# name -> (gamma, freeze). 'ModelD_full' is the existing run (gamma 2.0, freeze 11).
CANDIDATES = {
    'ModelD_full': (2.0, 11),
    'ModelD_g1.0_f11': (1.0, 11),
    'ModelD_g1.5_f11': (1.5, 11),
    'ModelD_g2.5_f11': (2.5, 11),
    'ModelD_g2.0_f9': (2.0, 9),
}

import torch
print('GPU:', torch.cuda.get_device_name(0) if torch.cuda.is_available() else 'NOT AVAILABLE')
assert torch.cuda.is_available(), 'No GPU: select the TOOL-26 (.venv) kernel.'
for seed in (42, 43, 44):
    assert (WEIGHTS_ROOT / f'best_ModelD2_lesion_ita_seed{seed}.pt').is_file(), f'Missing Stage 1 seed {seed}'
assert (RUNS / 'ModelD_full_seed42' / 'results.csv').is_file(), 'Missing the current full D run (seed 42)'
print('Ready.')


GPU: NVIDIA GeForce RTX 3050 Laptop GPU
Ready.


## Focal Loss with adjustable γ

In [2]:
import torch.nn as nn
import torch.nn.functional as F
from ultralytics.utils import loss as uloss

FOCAL_GAMMA = 2.0   # set per run before training


class ElementwiseFocalLoss(nn.Module):
    def __init__(self, gamma: float, alpha: float):
        super().__init__()
        self.gamma, self.alpha = gamma, alpha

    def forward(self, pred, label):
        loss = F.binary_cross_entropy_with_logits(pred, label, reduction='none')
        prob = pred.sigmoid()
        p_t = label * prob + (1 - label) * (1 - prob)
        loss = loss * (1.0 - p_t) ** self.gamma
        if self.alpha > 0:
            loss = loss * (label * self.alpha + (1 - label) * (1 - self.alpha))
        return loss


if not hasattr(uloss.v8DetectionLoss, '_init_without_focal'):
    uloss.v8DetectionLoss._init_without_focal = uloss.v8DetectionLoss.__init__

def _init_with_focal(self, *args, **kwargs):
    uloss.v8DetectionLoss._init_without_focal(self, *args, **kwargs)
    self.bce = ElementwiseFocalLoss(FOCAL_GAMMA, FOCAL_ALPHA)

uloss.v8DetectionLoss.__init__ = _init_with_focal

for g in (1.0, 1.5, 2.0, 2.5):
    pred, label = torch.randn(4, 50, 8), torch.rand(4, 50, 8)
    ours = ElementwiseFocalLoss(g, FOCAL_ALPHA)(pred, label).mean(1).sum()
    assert torch.allclose(ours, uloss.FocalLoss(gamma=g, alpha=FOCAL_ALPHA)(pred, label), atol=1e-6)
print('Focal Loss ready.')


Focal Loss ready.


## Train the 4 candidates (seed 42)

In [3]:
from ultralytics import YOLO


def checkpoint_state(checkpoint: Path) -> str:
    try:
        epoch = torch.load(checkpoint, map_location='cpu', weights_only=False).get('epoch', 0)
    except Exception:
        return 'corrupt'
    return 'finished' if epoch == -1 else 'resumable'


def train_stage2(name: str, seed: int) -> Path:
    global FOCAL_GAMMA
    gamma, freeze = CANDIDATES[name]
    destination = WEIGHTS_ROOT / f'best_{name}_seed{seed}.pt'
    if destination.is_file():
        print(f'{name} seed {seed}: already finished')
        return destination
    FOCAL_GAMMA = gamma   # read when the trainer builds the loss
    run = RUNS / f'{name}_seed{seed}'
    last = run / 'weights' / 'last.pt'
    state = checkpoint_state(last) if last.is_file() else 'missing'
    if state == 'corrupt':
        shutil.rmtree(run)
        state = 'missing'
    print(f'\n=== {name} seed {seed}: gamma {gamma}, freeze layers 0-{freeze - 1} ===')
    if state == 'resumable':
        YOLO(str(last)).train(resume=True)
    else:
        YOLO(str(WEIGHTS_ROOT / f'best_ModelD2_lesion_ita_seed{seed}.pt')).train(
            data=str(DATA_YAML), epochs=EPOCHS, patience=PATIENCE, imgsz=IMG_SIZE, batch=BATCH,
            seed=seed, deterministic=True, freeze=freeze, optimizer='AdamW', lr0=LR0, warmup_epochs=1,
            project=str(RUNS), name=f'{name}_seed{seed}', exist_ok=True, plots=True, verbose=True,
        )
    best = run / 'weights' / 'best.pt'
    assert best.is_file(), f'Missing validation-selected weights: {best}'
    shutil.copy2(best, destination)
    return destination


def best_validation(name: str, seed: int) -> dict:
    # Validation scores at the epoch Ultralytics kept as best.pt (max fitness = 0.9 mAP50-95 + 0.1 mAP50).
    rows = list(csv.DictReader(open(RUNS / f'{name}_seed{seed}' / 'results.csv')))
    fit = lambda r: 0.9 * float(r['metrics/mAP50-95(B)']) + 0.1 * float(r['metrics/mAP50(B)'])
    b = max(rows, key=fit)
    m50, m5095 = 100 * float(b['metrics/mAP50(B)']), 100 * float(b['metrics/mAP50-95(B)'])
    return {'candidate': name, 'seed': seed, 'gamma': CANDIDATES[name][0], 'freeze': CANDIDATES[name][1],
            'best_epoch': int(b['epoch']), 'val_mAP50': m50, 'val_mAP50_95': m5095, 'score': (m50 + m5095) / 2}


for name in CANDIDATES:
    if name != 'ModelD_full':
        train_stage2(name, 42)



=== ModelD_g1.0_f11 seed 42: gamma 1.0, freeze layers 0-10 ===


New https://pypi.org/project/ultralytics/8.4.168 available 😃 Update with 'pip install -U ultralytics'


Ultralytics 8.4.163 🚀 Python-3.14.4 torch-2.14.0+cu130 CUDA:0 (NVIDIA GeForce RTX 3050 Laptop GPU, 3770MiB)


engine/trainer: agnostic_nms=False, amp=True, angle=1.0, augment=False, auto_augment=randaugment, batch=8, bgr=0.0, box=7.5, cache=False, cfg=None, channels_last=None, classes=None, close_mosaic=10, cls=0.5, cls_pw=0.0, cls_remap=True, compile=False, conf=None, copy_paste=0.0, copy_paste_mode=flip, cos_lr=False, cutmix=0.0, data=/home/eney/Documents/TOOL2026/ablation_training/datasets/ablation_yolov26/ModelD2_lesion_ita/data.yaml, degrees=0.0, deterministic=True, device=, dfl=1.5, dgrad=0.5, dis=6.0, distill_model=None, dlam=1.0, dlog=1.0, dnn=False, dropout=0.0, dynamic=False, embed=None, epochs=150, erasing=0.4, exist_ok=True, fliplr=0.5, flipud=0.0, format=torchscript, fraction=1.0, freeze=11, hsv_h=0.015, hsv_s=0.7, hsv_v=0.4, imgsz=640, iou=0.7, keras=False, kobj=1.0, line_width=None, lr0=0.0002, lrf=0.01, mask_ratio=4, max_det=300, mixup=0.0, mode=train, model=/home/eney/Documents/TOOL2026/ablation_training/weights/ablation_split/best_ModelD2_lesion_ita_seed42.pt, momentum=0.937,


                   from  n    params  module                                       arguments                     


...

        Tinea corporis         53        100      0.653       0.61      0.616      0.337


           Tinea pedis         11         11      0.759      0.574       0.77      0.482


              Impetigo         58        260      0.474      0.504       0.41      0.158


Speed: 0.2ms preprocess, 2.8ms inference, 0.0ms loss, 3.5ms postprocess per image


Results saved to /home/eney/Documents/TOOL2026/ablation_training/runs/ablation_split/training/ModelD_g2.0_f9_seed42


## Select on validation

In [4]:
import pandas as pd
table = pd.DataFrame([best_validation(n, 42) for n in CANDIDATES]).sort_values('score', ascending=False)
table.to_csv(HERE / 'd_tuning_validation.csv', index=False)
print(table.round(2).to_string(index=False))
winner = table.iloc[0]['candidate']
print(f'\nWinner on validation: {winner}')


      candidate  seed  gamma  freeze  best_epoch  val_mAP50  val_mAP50_95  score
ModelD_g1.0_f11    42    1.0      11          16      45.43         21.43  33.43
ModelD_g1.5_f11    42    1.5      11          22      45.23         21.18  33.21
    ModelD_full    42    2.0      11          10      44.98         20.96  32.97
 ModelD_g2.0_f9    42    2.0       9          10      44.52         21.32  32.92
ModelD_g2.5_f11    42    2.5      11          80      44.27         21.42  32.85

Winner on validation: ModelD_g1.0_f11


## Winner: seeds 43 and 44

In [5]:
for seed in (43, 44):
    train_stage2(winner, seed)   # skipped when the winner is the existing full D
CHOICE_FILE.write_text(json.dumps({'winner': winner, 'gamma': CANDIDATES[winner][0],
                                   'freeze': CANDIDATES[winner][1], 'selection': 'mean of val mAP50 and mAP50-95, seed 42'},
                                  indent=2), encoding='utf-8')
print('Saved', CHOICE_FILE)



=== ModelD_g1.0_f11 seed 43: gamma 1.0, freeze layers 0-10 ===


New https://pypi.org/project/ultralytics/8.4.169 available 😃 Update with 'pip install -U ultralytics'


Ultralytics 8.4.163 🚀 Python-3.14.4 torch-2.14.0+cu130 CUDA:0 (NVIDIA GeForce RTX 3050 Laptop GPU, 3770MiB)


engine/trainer: agnostic_nms=False, amp=True, angle=1.0, augment=False, auto_augment=randaugment, batch=8, bgr=0.0, box=7.5, cache=False, cfg=None, channels_last=None, classes=None, close_mosaic=10, cls=0.5, cls_pw=0.0, cls_remap=True, compile=False, conf=None, copy_paste=0.0, copy_paste_mode=flip, cos_lr=False, cutmix=0.0, data=/home/eney/Documents/TOOL2026/ablation_training/datasets/ablation_yolov26/ModelD2_lesion_ita/data.yaml, degrees=0.0, deterministic=True, device=, dfl=1.5, dgrad=0.5, dis=6.0, distill_model=None, dlam=1.0, dlog=1.0, dnn=False, dropout=0.0, dynamic=False, embed=None, epochs=150, erasing=0.4, exist_ok=True, fliplr=0.5, flipud=0.0, format=torchscript, fraction=1.0, freeze=11, hsv_h=0.015, hsv_s=0.7, hsv_v=0.4, imgsz=640, iou=0.7, keras=False, kobj=1.0, line_width=None, lr0=0.0002, lrf=0.01, mask_ratio=4, max_det=300, mixup=0.0, mode=train, model=/home/eney/Documents/TOOL2026/ablation_training/weights/ablation_split/best_ModelD2_lesion_ita_seed43.pt, momentum=0.937,


                   from  n    params  module                                       arguments                     


...

           Tinea pedis         11         11      0.681      0.727      0.713      0.431


              Impetigo         58        260       0.61      0.458      0.483      0.192


Speed: 0.2ms preprocess, 2.9ms inference, 0.0ms loss, 1.4ms postprocess per image


Results saved to /home/eney/Documents/TOOL2026/ablation_training/runs/ablation_split/training/ModelD_g1.0_f11_seed44


Saved /home/eney/Documents/TOOL2026/ablation_training/final/d_tuning_choice.json


## Test set: SOP tables (A, B, C, chosen D)

In [6]:
# Test set, once: SOP tables with the chosen Model D.
import importlib
os.environ['SOP_MODELS'] = 'manuscript'
sys.path.insert(0, str(HERE))
import sop_analysis
importlib.reload(sop_analysis)
sop_analysis.main()
print((sop_analysis.OUT / 'SOP_RESULTS.md').read_text(encoding='utf-8'))


Model A (Baseline YOLOv26) seed 42: evaluating the 200 test images...


Ultralytics 8.4.163 🚀 Python-3.14.4 torch-2.14.0+cu130 CUDA:0 (NVIDIA GeForce RTX 3050 Laptop GPU, 3770MiB)


YOLO26n summary (fused): 120 layers, 2,376,396 parameters, 0 gradients, 5.3 GFLOPs


val: Fast image access ✅ (ping: 0.0±0.0 ms, read: 380.0±171.0 MB/s, size: 218.8 KB)


val: Scanning /home/eney/Documents/TOOL2026/ablation_training/datasets/ablation_yolov26/ModelA_raw/labels/test.cache... 200 images, 0 backgrounds, 0 corrupt: 100% ━━━━━━━━━━━━ 200/200 83.9Mit/s 0.0s

...

                 Class     Images  Instances      Box(P          R      mAP50  mAP50-95): 92% ━━━━━━━━━━━─ 23/25 10.5it/s 2.0s<0.2s

                 Class     Images  Instances      Box(P          R      mAP50  mAP50-95): 100% ━━━━━━━━━━━━ 25/25 11.4it/s 2.2s

                   all        200       1435        0.5      0.442      0.409      0.205


Speed: 0.2ms preprocess, 3.6ms inference, 0.0ms loss, 1.3ms postprocess per image



Done. Results in /home/eney/Documents/TOOL2026/ablation_training/final/sop_results_manuscript
# Statement of the Problem: results

Test set: 200 images (never used in training or calibration). Models A, B, C, D = A Baseline YOLOv26, B Fixed L*-CLAHE (β = 2.0), C Focal Loss Optimization, D ITA-guided L*-CLAHE + two-stage + Focal Loss (proposed).
mAP, precision, recall and F1 tables are the official Ultralytics test evaluation (P and R at the confidence that maximizes F1). Per-image scores for the tests and the confusion use confidence >= 0.25 and IoU >= 0.5. Paired tests use seed 42 for every model; models with more finished seeds also show mean ± SD.

## SOP 1: localization (mAP@50, mAP@50-95) and SOP 2: classification (P, R, F1)

| Model | mAP@50 | mAP@50-95 | Precision | Recall | F1 |
|---|---|---|---|---|---|
| A Baseline YOLOv26 (seed 42) | 42.6 | 19.0 | 45.2 | 47.9 | 46.5 |
| B Fixed L*-CLAHE (β = 2.0) (seed 42) | 39.5 | 20.3 | 50.2 | 41.6 | 45.5 |
| C Focal Loss Optimization (se